<img src="https://github.com/ArchiColab/sitex/blob/main/images/banner.png?raw=1" width="1000"/>

# Site 3D Model — CAD/BIM Export (LOD 300+, 2 × 2 km)

This notebook clips the fully attributed `buildings_enriched.gpkg` to a 2 × 2 km focus site of
your choice and exports CAD/BIM-ready geometry. Building height, function class, and
ground elevation were already attributed in `01-ARCH-Building_Morphology.ipynb`.

The exports are: a flat building DXF, a DEM-draped building DXF (footprints at their
ground elevation), a grouped `site.obj`, a smoothed land-cover DXF, a thickened,
colored land-cover `.obj`, a watertight terrain solid `.obj`, site contour lines (DXF),
and a draped land-use/water context DXF, plus an inline pydeck 3D preview.

**No height sampling or land-use classification here:** this notebook only clips and exports.

The notebook is optimized for Google Colab. Because it runs in the cloud, it can be used
on machines with limited computing power and in areas with limited bandwidth. It does not
download any new data; it reuses what the `00-` notebooks already fetched.

<img src="https://github.com/ArchiColab/sitex/blob/main/images/Site3D_overview.svg?raw=1" width="1000"/>

- **Library:** [`sitex`](https://github.com/ArchiColab/sitex)
- **Scale:** an exact 2 × 2 km site you pick, clipped from the district-scale model.

**Requires (run first):**
- `00-Data-Acquisition.ipynb` — `data/dem/dtm_nasadem.tif`, land cover, Overture land use + water
- `01-ARCH-Building_Morphology.ipynb` — `data/gdf/{slug}_buildings_enriched.gpkg`
  (which itself needs `00-Data-Acquisition_BuildingHeights.ipynb`)

**Shared CAD origin:**
All CAD exports use the same fixed reference point (`local_lat = 13.9833`,
`local_lon = 108.0000`) as `01-ARCH-DEM_Contour.ipynb`, not this site's own centroid.
A per-site origin would silently misalign Rhino/Revit models produced by the different
notebooks. Every export here, including the site contour DXF, is shifted by this origin
instead of being left in raw UTM coordinates.

**Output (`outputs/`; in Colab: `My Drive/SiteX_Outputs/`):**
- `{site_slug}_buildings_flat.dxf`
- `{site_slug}_buildings_dem.dxf`
- `{site_slug}_site.obj`
- `{site_slug}_landcover.dxf`
- `{site_slug}_landcover.obj`
- `{site_slug}_terrain.obj`
- `{site_slug}_contours.dxf`
- `{site_slug}_context.dxf`

No GeoPackage is written here; the district-scale buildings GeoPackage is the only one.

---
## 1. Install & import

<img src="https://github.com/ArchiColab/sitex/blob/main/images/Site3D_Setup.svg?raw=1" width="1000"/>


In [1]:
# One-time setup, if `sitex` isn't already installed in this kernel:
# %pip install "sitex[data,arch] @ git+https://github.com/ArchiColab/sitex.git" pydeck

import sys
IN_COLAB = "google.colab" in sys.modules
print("Running in:", "Google Colab" if IN_COLAB else "Local environment")

if IN_COLAB:
    from google.colab import drive
    drive.mount("/content/gdrive")
    %pip install "sitex[data,arch] @ git+https://github.com/ArchiColab/sitex.git" pydeck
    from google.colab import output
    output.enable_custom_widget_manager()


Running in: Local environment


In [2]:
#@title <font color=#1B7192> Imports </font>  { display-mode: "form" }

import warnings
import time
from pathlib import Path

import ezdxf
import geopandas as gpd
import matplotlib.cm as mpl_cm
import matplotlib.colors as mpl_colors
import numpy as np
import pandas as pd
import pyproj
import rasterio
import rasterio.features
import rasterio.windows
import trimesh
from shapely import constrained_delaunay_triangles
from shapely.geometry import box, shape
from shapely.ops import transform as shp_transform

from sitex.core.geo import compute_cad_origin, utm_epsg_from_lonlat
from sitex.data import aoi as aoi_lib
from sitex.arch import terrain

warnings.filterwarnings("ignore")
print("Imports OK.")


Imports OK.


## 2. Output directories

In [3]:
#@title <font color=#1B7192> Output Path </font>  { display-mode: "form" }

DATA_DIR = Path("/content/gdrive/MyDrive/Colab_Outputs") if IN_COLAB else Path("..") / "data"
GDF_DIR = DATA_DIR / "gdf"
LC_DIR = DATA_DIR / "landcover"
DEM_DIR = DATA_DIR / "dem"
OVT_DIR = DATA_DIR / "overture"
OUTPUT_DIR = Path("/content/gdrive/MyDrive/SiteX_Outputs") if IN_COLAB else Path("..") / "outputs"
OUTPUT_DIR.mkdir(parents=True, exist_ok=True)

print(f"District buildings_enriched.gpkg: {GDF_DIR.resolve()}")
print(f"Land cover              : {LC_DIR.resolve()}")
print(f"DEM                     : {DEM_DIR.resolve()}")
print(f"Overture (land use/water): {OVT_DIR.resolve()}")
print(f"Site outputs            : {OUTPUT_DIR.resolve()}")


District buildings_enriched.gpkg: C:\Users\Maddie\OneDrive\000_CIC2025\CIC2025\100 Lab Notes\Projects\CIC2025 Masterthesis\Experiments\data\gdf
Land cover              : C:\Users\Maddie\OneDrive\000_CIC2025\CIC2025\100 Lab Notes\Projects\CIC2025 Masterthesis\Experiments\data\landcover
DEM                     : C:\Users\Maddie\OneDrive\000_CIC2025\CIC2025\100 Lab Notes\Projects\CIC2025 Masterthesis\Experiments\data\dem
Overture (land use/water): C:\Users\Maddie\OneDrive\000_CIC2025\CIC2025\100 Lab Notes\Projects\CIC2025 Masterthesis\Experiments\data\overture
Site outputs            : C:\Users\Maddie\OneDrive\000_CIC2025\CIC2025\100 Lab Notes\Projects\CIC2025 Masterthesis\Experiments\outputs


---
## 3. District slug + shared CAD origin

<img src="https://github.com/ArchiColab/sitex/blob/main/images/Site3D_site.svg?raw=1" width="1000"/>

`DISTRICT_SLUG` must match the slug in the buildings file name,
`data/gdf/{slug}_buildings_enriched.gpkg` (default `pleiku`).

The CAD origin below is a **fixed shared point**, independent of both the district AOI
and the site you choose in the next section. It keeps all CAD exports across notebooks
aligned in the same Rhino/Revit coordinate system, so **do not change it** unless you
change it in every notebook.

In [4]:
_t0 = time.time()
print("### 3. District slug + shared CAD origin ###", flush=True)

DISTRICT_SLUG = "pleiku"

# Fixed shared-origin point -- matches 01-ARCH-DEM_Contour.ipynb exactly.
# Not the AOI's or the site's own centroid -- see the markdown above for why.
local_lat = 13.9833
local_lon = 108.0000

LOCAL_EPSG = utm_epsg_from_lonlat(local_lon, local_lat)
print(f"LOCAL_EPSG: {LOCAL_EPSG}")

ORIGIN_EASTING, ORIGIN_NORTHING = compute_cad_origin(local_lon, local_lat, LOCAL_EPSG)
print(f"Shared CAD origin: E={ORIGIN_EASTING:.0f}, N={ORIGIN_NORTHING:.0f}")

print(f"--- 3. done in {time.time() - _t0:.2f}s ---\n")


### 3. District slug + shared CAD origin ###
LOCAL_EPSG: 32649
Shared CAD origin: E=175000, N=1547000
--- 3. done in 0.01s ---



## 4. Load the district-scale attributed buildings

The buildings GeoPackage already has `height_final`, `height_source`, `bldg_function` and
`elevation_m`. It is stored in the local UTM zone (`EPSG:{LOCAL_EPSG}`, metric), not in
latitude/longitude.

In [5]:
#@title <font color=#1B7192> Load Buildings </font>  { display-mode: "form" }

_t0 = time.time()
print("### 4. Load the district-scale attributed buildings ###", flush=True)

district_buildings_path = GDF_DIR / f"{DISTRICT_SLUG}_buildings_enriched.gpkg"
if not district_buildings_path.exists():
    raise FileNotFoundError(
        f"{district_buildings_path} not found -- run 01-ARCH-Building_Morphology.ipynb "
        "for this slug first."
    )

# The GPKG can hold stale layers from older runs (e.g. "phường_pleiku_buildings_enriched",
# without height_final/height_source); read the layer 01-ARCH-Building_Morphology writes.
district_buildings = gpd.read_file(district_buildings_path, layer=district_buildings_path.stem)
# buildings_enriched.gpkg is saved in the local UTM zone; this check only reprojects
# if an older file (e.g. in EPSG:4326) is loaded.
if district_buildings.crs.to_epsg() != LOCAL_EPSG:
    print(f"Reprojecting from EPSG:{district_buildings.crs.to_epsg()} to EPSG:{LOCAL_EPSG}")
    district_buildings = district_buildings.to_crs(epsg=LOCAL_EPSG)

print(f"Loaded {len(district_buildings):,} attributed buildings from {district_buildings_path}")
height_source_counts = dict(district_buildings["height_source"].value_counts())
print(f"Height sources: {height_source_counts}")

print(f"--- 4. done in {time.time() - _t0:.2f}s ---\n")


### 4. Load the district-scale attributed buildings ###
Loaded 21,389 attributed buildings from ..\data\gdf\pleiku_buildings_enriched.gpkg
Height sources: {'open_buildings': 15548, 'gba': 5072, 'imputed': 769}
--- 4. done in 0.22s ---



## 5. Choose the 2 × 2 km site

The map opens with a 2 × 2 km box centered on the centroid of all district buildings,
so it is very likely to contain buildings.
**Keep the default box, or draw your own rectangle** over the exact site you want to
model in CAD. A drawn rectangle is used as drawn, so keep it close to 2 × 2 km; larger
sites make the CAD files heavy.

In [6]:
_default_centroid = district_buildings.to_crs(epsg=4326).geometry.union_all().centroid
SITE_CENTER_LAT = _default_centroid.y
SITE_CENTER_LON = _default_centroid.x
SITE_SLUG = "site_1"    #@param {type:"string"}
#@markdown <font color=#1B7192> Used only to name this notebook's output files -- change
#@markdown it if you're exporting more than one site from the same district. </font>

print(f"Default site centre (district buildings' own centroid): "
      f"({SITE_CENTER_LAT:.5f}, {SITE_CENTER_LON:.5f})")


Default site centre (district buildings' own centroid): (13.98918, 108.02076)


In [7]:
#@title <font color=#1B7192> Draw the site (optional -- default 2x2km box shown in yellow) </font>  { display-mode: "form" }
import json
import uuid

from IPython.display import display

# --- default 2 x 2 km box around the site centre (SITE_CENTER_LAT / SITE_CENTER_LON) ---
from pyproj import Transformer

_zone = int((SITE_CENTER_LON + 180) // 6) + 1
_utm = f"EPSG:{(32600 if SITE_CENTER_LAT >= 0 else 32700) + _zone}"
_to_utm = Transformer.from_crs("EPSG:4326", _utm, always_xy=True)
_to_ll = Transformer.from_crs(_utm, "EPSG:4326", always_xy=True)
_x, _y = _to_utm.transform(SITE_CENTER_LON, SITE_CENTER_LAT)
_west, _south = _to_ll.transform(_x - 1000, _y - 1000)
_east, _north = _to_ll.transform(_x + 1000, _y + 1000)
_default_site_bbox = (_west, _south, _east, _north)

_HTML = r"""
<link rel="stylesheet" href="https://cdn.jsdelivr.net/npm/leaflet@1.9.4/dist/leaflet.css"/>
<div id="__ID__status" style="font:14px sans-serif;margin:4px 0"><i>Click two opposite corners to draw a custom site. Yellow shows the default box, kept if you draw nothing.</i></div>
<div id="__ID__" style="height:480px;width:100%;cursor:crosshair"></div>
<script src="https://cdn.jsdelivr.net/npm/leaflet@1.9.4/dist/leaflet.js"></script>
<script>
(function () {
  var cfg = __CONFIG__;
  var statusEl = document.getElementById("__ID__status");
  function report() {
    var args = Array.prototype.slice.call(arguments);
    try { google.colab.kernel.invokeFunction(cfg.callback, args, {}); }
    catch (err) { statusEl.innerHTML = "<b>Could not reach Python: " + err + "</b>"; }
  }
  var map = L.map("__ID__", {scrollWheelZoom: true}).setView(cfg.center, cfg.zoom);
  L.tileLayer(cfg.tiles, {attribution: cfg.attribution, maxZoom: 19}).addTo(map);
  var d = cfg.defaultBbox;
  L.rectangle([[d[1], d[0]], [d[3], d[2]]], {color: "#FFFF00", weight: 2, fillOpacity: 0.08}).addTo(map);
  var first = null, dots = [], preview = null, drawn = null;
  function clear() {
    dots.forEach(function (x) { map.removeLayer(x); }); dots = [];
    if (preview) { map.removeLayer(preview); preview = null; }
    if (drawn) { map.removeLayer(drawn); drawn = null; }
  }
  map.on("mousemove", function (e) {
    if (!first) return;
    var b = [[first.lat, first.lng], [e.latlng.lat, e.latlng.lng]];
    if (preview) preview.setBounds(b);
    else preview = L.rectangle(b, {color: "#6bc2e5", weight: 2, fillOpacity: 0.1}).addTo(map);
  });
  map.on("click", function (e) {
    if (!first) {
      clear();
      first = e.latlng;
      dots.push(L.circleMarker(first, {radius: 4, color: "red"}).addTo(map));
      report();
      statusEl.innerHTML = "<i>Click 1/2 - click the opposite corner</i>";
      return;
    }
    var a = first, b = e.latlng;
    first = null;
    clear();
    var w = Math.min(a.lng, b.lng), s = Math.min(a.lat, b.lat);
    var ee = Math.max(a.lng, b.lng), n = Math.max(a.lat, b.lat);
    drawn = L.rectangle([[s, w], [n, ee]], {color: "red", weight: 2, fillOpacity: 0.15}).addTo(map);
    report(w, s, ee, n);
    statusEl.innerHTML = "<i>Site drawn (" + w.toFixed(5) + ", " + s.toFixed(5) + ", " + ee.toFixed(5) + ", " + n.toFixed(5) + "). Click again to redraw, or run the next cell to confirm.</i>";
  });
})();
</script>
"""

_drawn = {"value": None}


def _on_draw(*args):
    _drawn["value"] = tuple(float(v) for v in args) if len(args) == 4 else None


class _SiteMap:
    """Read back by sitex.data.aoi.resolve_aoi_from_map in the next cell."""

    def __init__(self, html, drawn):
        self._html = html
        self._sitex_drawn_bbox = drawn

    def _repr_html_(self):
        return self._html


if IN_COLAB:
    # Colab does not reliably show ipyleaflet widgets, so the map is a plain Leaflet page
    # and the two clicks reach Python through Colab's own callback.
    from google.colab import output

    _uid = uuid.uuid4().hex[:8]
    _callback = f"site_draw_{_uid}"
    output.register_callback(_callback, _on_draw)
    _config = json.dumps({
        "callback": _callback,
        "center": [SITE_CENTER_LAT, SITE_CENTER_LON],
        "zoom": 16,
        "tiles": "https://server.arcgisonline.com/ArcGIS/rest/services/World_Imagery/MapServer/tile/{z}/{y}/{x}",
        "attribution": "Tiles &copy; Esri",
        "defaultBbox": list(_default_site_bbox),
    })
    site_map = _SiteMap(_HTML.replace("__CONFIG__", _config).replace("__ID__", f"site_map_{_uid}"), _drawn)
else:
    site_map, _default_site_bbox = aoi_lib.build_aoi_map(SITE_CENTER_LAT, SITE_CENTER_LON, dist_m=1000, zoom=16)

print("Draw a rectangle over the exact site, or leave it and keep the default 2x2km "
      "box. Run the next cell to confirm.")

display(site_map)

Draw a rectangle over the exact site, or leave it and keep the default 2x2km box. Run the next cell to confirm.


In [8]:
#@title <font color=#1B7192> Confirm site </font>  { display-mode: "form" }
site_aoi = aoi_lib.resolve_aoi_from_map(site_map, _default_site_bbox, slug=SITE_SLUG)

west, south, east, north = site_aoi.bbox
print(f"Site bbox: (xmin={west:.5f}, ymin={south:.5f}, xmax={east:.5f}, ymax={north:.5f})")
print(f"Site centre: ({site_aoi.center_lat:.5f}, {site_aoi.center_lon:.5f})")


Site bbox: (xmin=108.01151, ymin=13.98015, xmax=108.03001, ymax=13.99821)
Site centre: (13.98918, 108.02076)


---
## 6. Clip buildings to the site

<img src="https://github.com/ArchiColab/sitex/blob/main/images/Site3D_buildings.svg?raw=1" width="1000"/>



In [9]:
#@title <font color=#1B7192> Clip buildings </font>  { display-mode: "form" }

_t0 = time.time()
print("### 6. Clip buildings to the site ###", flush=True)

site_boundary_local = gpd.GeoSeries([site_aoi.boundary], crs="EPSG:4326").to_crs(epsg=LOCAL_EPSG).iloc[0]

buildings = gpd.clip(district_buildings, site_boundary_local)
# A building straddling the site boundary can come back as a MultiPolygon --
# explode it so every later step (DEM sampling, extrusion, DXF/OBJ) works on
# single Polygons.
buildings = buildings.explode(index_parts=False).reset_index(drop=True)
buildings = buildings[buildings.geometry.geom_type == "Polygon"].copy()
buildings["bldg_id"] = range(len(buildings))
print(f"Clipped {len(district_buildings):,} district buildings -> {len(buildings):,} "
      f"Polygon rows in the {SITE_SLUG} site")

if len(buildings) == 0:
    raise RuntimeError(
        "No buildings inside this site -- draw a box over a built-up area, or check "
        "DISTRICT_SLUG matches the buildings_enriched.gpkg you meant to clip from."
    )

print(f"--- 6. done in {time.time() - _t0:.2f}s ---\n")


### 6. Clip buildings to the site ###
Clipped 21,389 district buildings -> 4,813 Polygon rows in the site_1 site
--- 6. done in 0.24s ---



## 7. Sample ground elevation (DTM base_z) for extrusion

Each building's base height (`base_z`) is sampled at its centroid from the same DTM
used for `terrain.obj`.

If the DTM is not available, the code falls back to the `elevation_m` column already
stored in `buildings_enriched.gpkg`, so buildings still follow the terrain.

Note: one centroid value per building means large footprints on steep slopes may partly
float above or sink into the terrain.

In [10]:
#@title <font color=#1B7192> Click to run </font>  { display-mode: "form" }

_t0 = time.time()
print("### 7. Sample ground elevation (DEM base_z) for extrusion ###", flush=True)

DTM_PATH = DEM_DIR / "dtm_nasadem.tif"

centroids_wgs = buildings.geometry.centroid.to_crs(epsg=4326)
lon = centroids_wgs.x.values
lat = centroids_wgs.y.values

if DTM_PATH.exists():
    with rasterio.open(DTM_PATH) as dtm:
        nodata = dtm.nodata
        base_z = np.array([next(dtm.sample([(lon[i], lat[i])]))[0] for i in range(len(lon))], dtype=float)
    bad = (base_z == nodata) | np.isnan(base_z)
    if bad.any():
        base_z[bad] = np.nanmedian(base_z[~bad]) if (~bad).any() else 0.0
    print(f"DEM sample: {bad.sum():,} / {len(base_z):,} buildings outside raster coverage / nodata")
else:
    print(f"[SKIPPED] {DTM_PATH} not found -- falling back to the elevation_m column "
          "in buildings_enriched.gpkg.")
    base_z = buildings["elevation_m"].to_numpy(dtype=float)
    if np.isnan(base_z).all():
        base_z = np.zeros(len(buildings))

print(f"base_z min/mean/max: {np.nanmin(base_z):.1f} / {np.nanmean(base_z):.1f} / {np.nanmax(base_z):.1f} m")

print(f"--- 7. done in {time.time() - _t0:.2f}s ---\n")


### 7. Sample ground elevation (DEM base_z) for extrusion ###
DEM sample: 0 / 4,813 buildings outside raster coverage / nodata
base_z min/mean/max: 711.0 / 748.7 / 786.0 m
--- 7. done in 0.61s ---



## 8. Extrude helper

Footprints from different sources store their outlines in different directions
(clockwise or counter-clockwise). The helper first puts every outline in the same
direction (outer ring counter-clockwise, courtyard holes clockwise), then builds the
walls, including the inner walls around courtyards, so every face points outward.
Together with the closed floor and roof, this gives a watertight solid for each building.

This cell also shifts the site buildings to the shared CAD origin.

In [11]:
#@title <font color=#1B7192> Extrude helper </font>  { display-mode: "form" }

from shapely.geometry.polygon import orient

_t0 = time.time()
print("### 8. Extrude helper + shift to CAD origin ###", flush=True)

def polygon_rings(poly):
    """Oriented rings of ``poly``: exterior counter-clockwise, holes clockwise,
    closing point dropped, rings with fewer than 3 points skipped. Returns
    ``(oriented_poly, [ring_xy, ...])`` -- ``[]`` if the exterior is degenerate.
    """
    poly = orient(poly, sign=1.0)
    rings = []
    for k, r in enumerate([poly.exterior, *poly.interiors]):
        pts = np.asarray(r.coords)[:, :2]
        if len(pts) >= 2 and np.allclose(pts[0], pts[-1]):
            pts = pts[:-1]
        if len(pts) < 3:
            if k == 0:
                return poly, []
            continue
        rings.append(pts)
    return poly, rings


def extrude_footprint(poly, base_z, height):
    """Extrude one footprint, courtyard holes included, into a watertight solid.

    ``base_z`` is a scalar (buildings sit on one ground point) or a per-vertex
    array over all rings in ``polygon_rings()`` order (draped land cover, where
    each vertex's own terrain height differs) -- ``broadcast_to`` makes both
    paths run through the same code.
    """
    poly, rings = polygon_rings(poly)
    if not rings:
        return None
    ring_xy = np.vstack(rings)
    n = len(ring_xy)

    base_z_arr = np.broadcast_to(np.asarray(base_z, dtype=float), n)
    bottom = np.column_stack([ring_xy, base_z_arr])
    top = np.column_stack([ring_xy, base_z_arr + height])
    verts = np.vstack([bottom, top])

    # Floor + roof: triangulate the polygon (holes respected), floor facing down, roof up.
    index_of = {tuple(np.round(p, 6)): i for i, p in enumerate(ring_xy)}
    faces = []
    for tri in constrained_delaunay_triangles(poly).geoms:
        pts = np.asarray(tri.exterior.coords)[:3, :2]
        idx = [index_of.get(tuple(np.round(p, 6))) for p in pts]
        if None in idx:
            continue
        a, b, c = idx
        ax, ay = ring_xy[a]; bx, by = ring_xy[b]; cx, cy = ring_xy[c]
        signed_area2 = (bx - ax) * (cy - ay) - (cx - ax) * (by - ay)
        if signed_area2 < 0:
            faces.append((a, b, c))
            faces.append((n + a, n + c, n + b))
        else:
            faces.append((a, c, b))
            faces.append((n + a, n + b, n + c))

    # Walls: with the exterior counter-clockwise and holes clockwise, the same
    # winding points every wall away from the solid -- outward on the outer
    # ring, into the courtyard on a hole.
    offset = 0
    for ring in rings:
        m = len(ring)
        for k in range(m):
            i, j = offset + k, offset + (k + 1) % m
            faces.append((i, j, n + j))
            faces.append((i, n + j, n + i))
        offset += m

    return verts, np.array(faces, dtype=np.int64)


buildings_local = buildings.copy()
buildings_local["geometry"] = buildings_local.translate(-ORIGIN_EASTING, -ORIGIN_NORTHING)
buildings_local.crs = None
print(f"Shifted {len(buildings_local):,} site buildings to the shared CAD origin.")

print(f"--- 8. done in {time.time() - _t0:.2f}s ---\n")


### 8. Extrude helper + shift to CAD origin ###
Shifted 4,813 site buildings to the shared CAD origin.
--- 8. done in 0.29s ---



## 9. Export flat DXF (Z=0)

In [12]:
#@title <font color=#1B7192> Click to run </font>  { display-mode: "form" }

_t0 = time.time()
print("### 9. Export flat DXF (Z=0) ###", flush=True)

flat_dxf_path = OUTPUT_DIR / f"{SITE_SLUG}_buildings_flat.dxf"
doc = ezdxf.new(dxfversion="R2010")
msp = doc.modelspace()

for geom, func in zip(buildings_local.geometry.values, buildings_local["bldg_function"].values):
    if geom is None or geom.is_empty:
        continue
    layer = f"BLDG_{str(func).upper()}"
    rings = [list(geom.exterior.coords)] + [list(r.coords) for r in geom.interiors]
    for ring in rings:
        msp.add_lwpolyline([(x, y) for x, y in ring], dxfattribs={"layer": layer})

doc.saveas(flat_dxf_path)
print(f"Saved (flat, Z=0, origin-shifted E-{ORIGIN_EASTING:.0f}/N-{ORIGIN_NORTHING:.0f}): {flat_dxf_path}")

print(f"--- 9. done in {time.time() - _t0:.2f}s ---\n")


### 9. Export flat DXF (Z=0) ###
Saved (flat, Z=0, origin-shifted E-175000/N-1547000): ..\outputs\site_1_buildings_flat.dxf
--- 9. done in 1.67s ---



## 10. Export DEM-draped DXF (footprints at real base_z, no roof)

In [13]:
#@title <font color=#1B7192> Click to run </font>  { display-mode: "form" }

_t0 = time.time()
print("### 10. Export DEM-draped DXF (footprints at real base_z, no roof) ###", flush=True)

dem_dxf_path = OUTPUT_DIR / f"{SITE_SLUG}_buildings_dem.dxf"
doc_dem = ezdxf.new(dxfversion="R2010")
msp_dem = doc_dem.modelspace()

n_written = 0
for geom, func, bz in zip(buildings_local.geometry.values, buildings_local["bldg_function"].values, base_z):
    if geom is None or geom.is_empty:
        continue
    layer = f"BLDG_{str(func).upper()}"
    rings = [list(geom.exterior.coords)] + [list(r.coords) for r in geom.interiors]
    for ring in rings:
        pts_3d = [(x, y, float(bz)) for x, y in ring]
        msp_dem.add_polyline3d(pts_3d, dxfattribs={"layer": layer})
    n_written += 1

doc_dem.saveas(dem_dxf_path)
print(f"Saved {n_written:,} footprints on the DEM (own base_z each, no roof extrusion) -> {dem_dxf_path}")

print(f"--- 10. done in {time.time() - _t0:.2f}s ---\n")


### 10. Export DEM-draped DXF (footprints at real base_z, no roof) ###


Saved 4,813 footprints on the DEM (own base_z each, no roof extrusion) -> ..\outputs\site_1_buildings_dem.dxf
--- 10. done in 8.37s ---



## 11. Export `site.obj` (grouped by function)

Each building function (residential, mixed, industrial, …) is written as its own named
object. In Rhino's OBJ import options, import these objects as separate objects or as
layers; you can then select, hide, or delete a whole functional group at once. To edit a single
building, run `SplitDisjointMesh` on its object. To turn buildings into polysurfaces,
follow with `MeshToNURB` and then `MergeAllCoplanarFaces` to get clean walls and roofs.
At 2 × 2 km the file is small enough to open directly.

In [14]:
#@title <font color=#1B7192> Click to run </font>  { display-mode: "form" }

_t0 = time.time()
print("### 11. Export site.obj (grouped by function, watertight, winding-consistent) ###", flush=True)

def build_group_mesh(geoms, heights, base_zs):
    all_verts, all_faces = [], []
    v_offset = 0
    skipped = 0
    for geom, h, bz in zip(geoms, heights, base_zs):
        if geom is None or geom.is_empty or h is None or not np.isfinite(h) or h <= 0:
            skipped += 1
            continue
        result = extrude_footprint(geom, float(bz), float(h))
        if result is None:
            skipped += 1
            continue
        verts, faces = result
        all_verts.append(verts)
        all_faces.append(faces + v_offset)
        v_offset += len(verts)
    if not all_verts:
        return None, skipped
    return trimesh.Trimesh(vertices=np.vstack(all_verts), faces=np.vstack(all_faces), process=False), skipped


def export_grouped_obj(named_meshes, out_path, colors=None):
    """Write a multi-object Wavefront OBJ by hand, one ``o <name>`` block per mesh.

    ``trimesh.Scene.export()`` is what this notebook used to call here -- it
    reproducibly crashes the interpreter in this environment for ANY
    multi-geometry scene (confirmed with a minimal 2-box repro, independent of
    face count), while a single ``Trimesh.export()`` and this hand-rolled
    writer both work fine. Same category of environment fragility as the
    matplotlib-rendering crashes documented elsewhere in this project --
    avoid the broken code path rather than work around it downstream.

    ``colors``, if given, is ``{name: (r, g, b)}`` (0-1 floats) -- writes a
    sidecar ``.mtl`` with one material per named mesh, so viewers that read
    OBJ materials (Rhino, Blender, trimesh) show each group in its own
    colour without needing per-viewer manual styling. Verified round-trip
    through ``trimesh.load()`` before relying on it here.
    """
    mtl_path = None
    if colors:
        mtl_path = Path(out_path).with_suffix(".mtl")
        mtl_lines = []
        for name, _ in named_meshes:
            r, g, b = colors.get(name, (0.7, 0.7, 0.7))
            mtl_lines += [f"newmtl {name}", f"Kd {r:.3f} {g:.3f} {b:.3f}", "Ka 0.000 0.000 0.000", "d 1.0", ""]
        mtl_path.write_text("\n".join(mtl_lines), encoding="utf-8")

    lines = ["# grouped OBJ, written by hand -- trimesh.Scene.export() crashes here"]
    if mtl_path is not None:
        lines.append(f"mtllib {mtl_path.name}")
    v_offset = 0
    for name, mesh in named_meshes:
        lines.append(f"o {name}")
        if colors:
            lines.append(f"usemtl {name}")
        for v in mesh.vertices:
            lines.append(f"v {v[0]:.6f} {v[1]:.6f} {v[2]:.6f}")
        for f in mesh.faces:
            a, b, c = f + v_offset + 1  # OBJ vertex indices are 1-based, file-wide
            lines.append(f"f {a} {b} {c}")
        v_offset += len(mesh.vertices)
    Path(out_path).write_text("\n".join(lines), encoding="utf-8")
    return mtl_path


site_obj_path = OUTPUT_DIR / f"{SITE_SLUG}_site.obj"
functions = buildings_local["bldg_function"].to_numpy()

named_meshes = []
total_skipped = 0
for func in sorted(set(functions)):
    mask = functions == func
    mesh, skipped = build_group_mesh(
        buildings_local.geometry.values[mask],
        buildings_local["height_final"].values[mask],
        base_z[mask],
    )
    total_skipped += skipped
    if mesh is not None:
        named_meshes.append((f"BLDG_{str(func).upper()}", mesh))
        print(f"  {func}: {mask.sum():,} buildings -> {len(mesh.vertices):,} verts, {len(mesh.faces):,} faces")

export_grouped_obj(named_meshes, site_obj_path)
print(f"Skipped {total_skipped:,} buildings (invalid geometry/height)")
print(f"Saved -- {len(named_meshes)} objects (one per function, no Explode needed): {site_obj_path}  "
      f"({site_obj_path.stat().st_size/1e6:.2f} MB)")

print(f"--- 11. done in {time.time() - _t0:.2f}s ---\n")


### 11. Export site.obj (grouped by function, watertight, winding-consistent) ###
  industrial: 5 buildings -> 126 verts, 232 faces
  mixed: 1 buildings -> 12 verts, 20 faces
  residential: 4,807 buildings -> 44,864 verts, 70,500 faces
Skipped 0 buildings (invalid geometry/height)
Saved -- 3 objects (one per function, no Explode needed): ..\outputs\site_1_site.obj  (3.13 MB)
--- 11. done in 4.50s ---



## 12. Export smoothed land-cover DXF, clipped to the site

This section reads only the site's window of the land-cover raster before vectorizing it.
The smoothed polygons are also kept in `landcover_smoothed_utm`, so Section 13 can build
the draped land-cover mesh from them.

In [15]:
#@title <font color=#1B7192> Click to run </font>  { display-mode: "form" }

_t0 = time.time()
print("### 12. Export smoothed land-cover DXF, clipped to the site ###", flush=True)

WC_CLASSES = {
    10: "TREE_COVER", 20: "SHRUBLAND", 30: "GRASSLAND", 40: "CROPLAND",
    50: "BUILT_UP", 60: "BARE_SPARSE", 70: "SNOW_ICE", 80: "PERMANENT_WATER",
    90: "HERBACEOUS_WETLAND", 95: "MANGROVES", 100: "MOSS_LICHEN",
}

LC_SMOOTH_TOLERANCE_M = 8.0    #@param {type:"number"}
#@markdown <font color=#1B7192> Rounds off the raster's pixel-stairstep edges -- roughly
#@markdown one WorldCover pixel (10m) removes most of the "broken"/blocky look without
#@markdown erasing real shape detail. Set to 0 for the raw unsmoothed pixel boundaries. </font>


def smooth_polygon(poly, tolerance_m):
    if tolerance_m <= 0:
        return [poly]
    closed = poly.buffer(tolerance_m, join_style="round").buffer(-tolerance_m, join_style="round")
    opened = closed.buffer(-tolerance_m, join_style="round").buffer(tolerance_m, join_style="round")
    simplified = opened.simplify(tolerance_m, preserve_topology=True)
    if simplified.is_empty:
        return []
    if simplified.geom_type == "Polygon":
        return [simplified]
    if simplified.geom_type == "MultiPolygon":
        return list(simplified.geoms)
    return []


def window_from_bounds(left, bottom, right, top, transform):
    """Pixel window covering a bbox, without ``rasterio.windows.from_bounds()``.

    That function reproducibly crashes the interpreter in this environment
    (confirmed with a minimal repro -- just the function call, no file I/O
    involved) -- same category of environment fragility as the matplotlib
    and ``trimesh.Scene.export()`` crashes documented elsewhere in this
    project. ``~transform`` (the affine inverse) and ``Window.intersection()``
    both work fine, so build the window from those directly instead.
    """
    inv = ~transform
    col_off, row_off = inv * (left, top)
    col_end, row_end = inv * (right, bottom)
    return rasterio.windows.Window(col_off, row_off, col_end - col_off, row_end - row_off)


wc_path = LC_DIR / f"esa_worldcover_2021_{DISTRICT_SLUG}.tif"
lc_dxf_path = OUTPUT_DIR / f"{SITE_SLUG}_landcover.dxf"

landcover_smoothed_utm = []  # (layer_name, smoothed polygon in UTM, unshifted) -- reused by Section 13's landcover.obj

if not wc_path.exists():
    print(f"[SKIPPED] {wc_path} not found -- run 00-Data-Acquisition.ipynb Section 7 first.")
else:
    with rasterio.open(wc_path) as src:
        site_bounds_native = rasterio.warp.transform_bounds("EPSG:4326", src.crs, west, south, east, north)
        window = window_from_bounds(*site_bounds_native, transform=src.transform)
        window = window.intersection(rasterio.windows.Window(0, 0, src.width, src.height))
        wc_data = src.read(1, window=window)
        wc_transform = rasterio.windows.transform(window, src.transform)
        wc_crs = src.crs

    doc_lc = ezdxf.new(dxfversion="R2010")
    msp_lc = doc_lc.modelspace()
    transformer_to_utm = pyproj.Transformer.from_crs(wc_crs, f"EPSG:{LOCAL_EPSG}", always_xy=True)
    n_polys = 0
    n_skipped = 0
    for code_val, layer_name in WC_CLASSES.items():
        mask = wc_data == code_val
        if not mask.any():
            continue
        for geom_geojson, value in rasterio.features.shapes(wc_data, mask=mask, transform=wc_transform):
            poly = shape(geom_geojson)
            poly_utm = shp_transform(transformer_to_utm.transform, poly)
            smoothed_polys = smooth_polygon(poly_utm, LC_SMOOTH_TOLERANCE_M)
            if not smoothed_polys:
                n_skipped += 1
                continue
            for smoothed_utm in smoothed_polys:
                landcover_smoothed_utm.append((layer_name, smoothed_utm))
                poly_local = shp_transform(lambda x, y: (x - ORIGIN_EASTING, y - ORIGIN_NORTHING), smoothed_utm)
                rings = [list(poly_local.exterior.coords)] + [list(r.coords) for r in poly_local.interiors]
                for ring in rings:
                    msp_lc.add_lwpolyline([(x, y) for x, y in ring], dxfattribs={"layer": f"LC_{layer_name}"})
                n_polys += 1

    doc_lc.saveas(lc_dxf_path)
    print(f"Saved {n_polys:,} land-cover polygons (site window only) -> {lc_dxf_path}")
    print(f"Smoothing tolerance: {LC_SMOOTH_TOLERANCE_M:.1f}m -- {n_skipped:,} tiny/noise polygons dropped")

print(f"--- 12. done in {time.time() - _t0:.2f}s ---\n")


### 12. Export smoothed land-cover DXF, clipped to the site ###
Saved 282 land-cover polygons (site window only) -> ..\outputs\site_1_landcover.dxf
Smoothing tolerance: 8.0m -- 266 tiny/noise polygons dropped
--- 12. done in 1.90s ---



## 13. Land cover mesh, draped on terrain

<img src="https://github.com/ArchiColab/sitex/blob/main/images/Site3D_landcover.svg?raw=1" width="1000"/>

The land-cover polygons from Section 12 are exported as a mesh (`.obj`) that follows
the terrain. Each polygon becomes a thin slab, `LC_THICKNESS_M` thick, whose base follows
the ground height at every vertex. It uses the same `extrude_footprint()` helper as the
buildings (Section 8), extended to accept a separate base height per vertex. Because the
slab has real thickness, it sits visibly on top of the terrain solid instead of
flickering against it (z-fighting).

Each land-cover class gets its own color (`LC_COLORS` below), written to a sidecar
`.mtl` file with the same `export_grouped_obj()` used for `site.obj`. Tree cover,
shrubland, grassland, and cropland use different greens; built-up, bare ground, and
water use their conventional colors. Keep the `.mtl` in the same folder as the `.obj`,
or Rhino will import it without colors.

In [16]:
#@title <font color=#1B7192> Build & export the land cover mesh </font>  { display-mode: "form" }
_t0 = time.time()
print("### 13. Land cover mesh, draped on terrain ###", flush=True)

LC_THICKNESS_M = 0.3    #@param {type:"number"}
#@markdown <font color=#1B7192> Slab thickness above the draped terrain -- enough to
#@markdown read as a solid in a render, thin enough not to visually detach from the
#@markdown ground. </font>

LC_COLORS = {
    "LC_TREE_COVER": (0.10, 0.45, 0.12),      # dark green
    "LC_SHRUBLAND": (0.42, 0.55, 0.20),       # olive green
    "LC_GRASSLAND": (0.55, 0.75, 0.32),       # light green
    "LC_CROPLAND": (0.75, 0.80, 0.28),        # yellow-green
    "LC_BUILT_UP": (0.55, 0.55, 0.55),        # grey
    "LC_BARE_SPARSE": (0.75, 0.65, 0.45),     # tan
    "LC_SNOW_ICE": (0.95, 0.95, 0.95),        # white
    "LC_PERMANENT_WATER": (0.20, 0.45, 0.75), # blue
    "LC_HERBACEOUS_WETLAND": (0.30, 0.60, 0.55),  # teal-green
    "LC_MANGROVES": (0.05, 0.35, 0.25),       # deep green
    "LC_MOSS_LICHEN": (0.60, 0.65, 0.55),     # pale green-grey
}

landcover_obj_path = OUTPUT_DIR / f"{SITE_SLUG}_landcover.obj"

if not landcover_smoothed_utm:
    print("[SKIPPED] No land-cover polygons (Section 12 skipped or empty) -- no landcover.obj.")
elif not DTM_PATH.exists():
    print(f"[SKIPPED] {DTM_PATH} not found -- draping needs a DTM.")
else:
    transformer_to_wgs = pyproj.Transformer.from_crs(f"EPSG:{LOCAL_EPSG}", "EPSG:4326", always_xy=True)
    by_class = {}
    n_skipped_tri = 0

    with rasterio.open(DTM_PATH) as dtm:
        nodata = dtm.nodata
        for layer_name, poly_utm in landcover_smoothed_utm:
            _, rings_utm = polygon_rings(poly_utm)
            if not rings_utm:
                n_skipped_tri += 1
                continue
            ring_utm = np.vstack(rings_utm)  # all rings, same vertex order as extrude_footprint()

            lon, lat = transformer_to_wgs.transform(ring_utm[:, 0], ring_utm[:, 1])
            z = np.array([next(dtm.sample([(lon[i], lat[i])]))[0] for i in range(len(lon))], dtype=float)
            bad = (z == nodata) | np.isnan(z)
            if bad.any():
                z[bad] = np.nanmedian(z[~bad]) if (~bad).any() else 0.0

            poly_local = shp_transform(lambda x, y: (x - ORIGIN_EASTING, y - ORIGIN_NORTHING), poly_utm)
            result = extrude_footprint(poly_local, z, LC_THICKNESS_M)
            if result is None:
                n_skipped_tri += 1
                continue
            verts, faces = result
            by_class.setdefault(layer_name, []).append((verts, faces))

    named_meshes_lc = []
    for layer_name, parts in by_class.items():
        all_verts, all_faces = [], []
        v_offset = 0
        for verts, faces in parts:
            all_verts.append(verts)
            all_faces.append(faces + v_offset)
            v_offset += len(verts)
        mesh = trimesh.Trimesh(vertices=np.vstack(all_verts), faces=np.vstack(all_faces), process=False)
        named_meshes_lc.append((f"LC_{layer_name}", mesh))
        print(f"  {layer_name}: {len(parts):,} polygons -> {len(mesh.vertices):,} verts, {len(mesh.faces):,} faces")

    export_grouped_obj(named_meshes_lc, landcover_obj_path, colors=LC_COLORS)
    print(f"Skipped {n_skipped_tri:,} polygons that failed to triangulate/extrude")
    print(f"Saved -- {len(named_meshes_lc)} objects, {LC_THICKNESS_M:.1f}m thick, coloured per class -> "
          f"{landcover_obj_path}  ({landcover_obj_path.stat().st_size/1e6:.2f} MB)")

print(f"--- 13. done in {time.time() - _t0:.2f}s ---\n")


### 13. Land cover mesh, draped on terrain ###
  TREE_COVER: 94 polygons -> 2,488 verts, 4,696 faces
  GRASSLAND: 66 polygons -> 1,160 verts, 2,088 faces
  CROPLAND: 60 polygons -> 1,052 verts, 1,900 faces
  BUILT_UP: 56 polygons -> 1,730 verts, 3,380 faces
  BARE_SPARSE: 6 polygons -> 64 verts, 104 faces
Skipped 0 polygons that failed to triangulate/extrude
Saved -- 5 objects, 0.3m thick, coloured per class -> ..\outputs\site_1_landcover.obj  (0.46 MB)
--- 13. done in 1.60s ---



## 14. Overture land use + water, cropped to site

Unlike land cover (Section 12), Overture land use and water are already vector polygons
with class labels, so they need no rasterize-and-smooth step. They are simply clipped
to the site:

- **Land use** comes from its own file, `{DISTRICT_SLUG}_landuse.gpkg`.
- **Water** has no separate file; it is the `WATER` layer inside
  `{DISTRICT_SLUG}_overture.gpkg`.

Both are clipped in Overture's original coordinate system (`EPSG:4326`, latitude/longitude)
and reprojected later, when they are draped on the DEM for the context DXF.

In [17]:
#@title <font color=#1B7192> Load & clip Overture land use + water </font>  { display-mode: "form" }
_t0 = time.time()
print("### 14. Overture land use + water, cropped to site ###", flush=True)

landuse_path = OVT_DIR / f"{DISTRICT_SLUG}_landuse.gpkg"
overture_main_path = OVT_DIR / f"{DISTRICT_SLUG}_overture.gpkg"
site_boundary_wgs = site_aoi.boundary  # WGS84 -- see Section 6's site_boundary_local for the UTM version


def _load_and_clip(path, layer, mask):
    if not path.exists():
        print(f"[SKIPPED] {path} not found.")
        return gpd.GeoDataFrame(columns=["class", "geometry"], geometry="geometry", crs="EPSG:4326")
    gdf = gpd.read_file(path, layer=layer) if layer else gpd.read_file(path)
    return gpd.clip(gdf, mask)


landuse_site = _load_and_clip(landuse_path, None, site_boundary_wgs)
water_site = _load_and_clip(overture_main_path, "WATER", site_boundary_wgs)

lu_classes = sorted(landuse_site["class"].dropna().unique()) if len(landuse_site) else []
print(f"Land use polygons in site: {len(landuse_site):,}  classes={lu_classes}")
print(f"Water polygons in site   : {len(water_site):,}")

print(f"--- 14. done in {time.time() - _t0:.2f}s ---\n")


### 14. Overture land use + water, cropped to site ###
Land use polygons in site: 5  classes=['farmland', 'hospital', 'residential']
Water polygons in site   : 0
--- 14. done in 0.04s ---



## 15. Terrain solid mesh from the DEM (site-cropped)

The terrain is exported as a closed, watertight block, not just a surface:

- **Top face:** follows the DEM terrain. The DEM is resampled (bilinear) onto a regular
  grid aligned with the UTM axes, so the mesh stays square after reprojection instead of
  being slightly skewed like the raw raster grid.
- **Four side walls:** run straight down from the terrain edge.
- **Flat bottom:** placed `TERRAIN_BASE_OFFSET_M` (default 50 m) below the lowest point
  of the site. This makes a shallow base, like a site model on a plinth, rather than
  a block reaching down to sea level.

The DEM is cropped to the site before meshing, so the grid stays small even at a fine
resolution.

In [18]:
#@title <font color=#1B7192> Build & export the terrain solid </font>  { display-mode: "form" }
_t0 = time.time()
print("### 15. Terrain solid mesh from the DEM (site-cropped) ###", flush=True)

from rasterio.transform import from_origin
from rasterio.warp import reproject, Resampling

TERRAIN_RESOLUTION_M = 10.0    #@param {type:"number"}
#@markdown <font color=#1B7192> Grid spacing of the terrain mesh, in metres. 10m keeps a
#@markdown 2x2km site under ~200x200 cells -- reads as terrain, stays light in Rhino. </font>
TERRAIN_BASE_OFFSET_M = 50.0    #@param {type:"number"}
#@markdown <font color=#1B7192> Flat bottom of the solid, this many metres BELOW the
#@markdown site's own lowest sampled elevation -- not an absolute Z. Gives a shallow
#@markdown pedestal instead of a shaft down to sea level. </font>

terrain_obj_path = OUTPUT_DIR / f"{SITE_SLUG}_terrain.obj"

if not DTM_PATH.exists():
    print(f"[SKIPPED] {DTM_PATH} not found -- no terrain mesh without a DTM.")
else:
    minx, miny, maxx, maxy = site_boundary_local.bounds
    nx = int(np.ceil((maxx - minx) / TERRAIN_RESOLUTION_M)) + 1
    ny = int(np.ceil((maxy - miny) / TERRAIN_RESOLUTION_M)) + 1
    dst_transform = from_origin(minx, maxy, TERRAIN_RESOLUTION_M, TERRAIN_RESOLUTION_M)

    with rasterio.open(DTM_PATH) as dtm:
        z_grid = np.full((ny, nx), np.nan, dtype=float)
        reproject(
            source=rasterio.band(dtm, 1),
            destination=z_grid,
            src_transform=dtm.transform,
            src_crs=dtm.crs,
            src_nodata=dtm.nodata,
            dst_transform=dst_transform,
            dst_crs=f"EPSG:{LOCAL_EPSG}",
            dst_nodata=np.nan,
            resampling=Resampling.bilinear,
        )

    bad = np.isnan(z_grid)
    if bad.all():
        raise RuntimeError("DTM has no coverage over this site -- can't build a terrain mesh.")
    if bad.any():
        z_grid[bad] = np.nanmedian(z_grid[~bad])
        print(f"Filled {bad.sum():,} / {z_grid.size:,} nodata cells with the site median elevation")

    TERRAIN_BASE_Z = float(np.nanmin(z_grid)) - TERRAIN_BASE_OFFSET_M

    xs = minx + (np.arange(nx) + 0.5) * TERRAIN_RESOLUTION_M
    ys = maxy - (np.arange(ny) + 0.5) * TERRAIN_RESOLUTION_M

    def build_terrain_solid(x, y, z, base_z):
        """Watertight block: top = heightfield, 4 ruled walls, flat bottom cap.

        Winding isn't reasoned about per-face (unlike ``extrude_footprint``'s
        per-ring orientation check in Section 8) -- ``fix_normals()`` corrects
        it after the fact, which is simpler and just as reliable for a
        regular grid.
        """
        ny_, nx_ = z.shape
        xx, yy = np.meshgrid(x, y)
        top = np.column_stack([xx.ravel(), yy.ravel(), z.ravel()])

        def idx(r, c):
            return r * nx_ + c

        faces = []
        for r in range(ny_ - 1):
            for c in range(nx_ - 1):
                a, b, cc, d = idx(r, c), idx(r, c + 1), idx(r + 1, c), idx(r + 1, c + 1)
                faces.append((a, b, cc))
                faces.append((b, d, cc))

        # Perimeter ring, walked once around the grid boundary (N -> E -> S -> W).
        ring = (
            [idx(0, c) for c in range(nx_)]
            + [idx(r, nx_ - 1) for r in range(1, ny_)]
            + [idx(ny_ - 1, c) for c in range(nx_ - 2, -1, -1)]
            + [idx(r, 0) for r in range(ny_ - 2, 0, -1)]
        )
        bottom_start = len(top)
        bottom = np.column_stack([top[ring, 0], top[ring, 1], np.full(len(ring), base_z)])
        verts = np.vstack([top, bottom])

        m = len(ring)
        for i in range(m):
            j = (i + 1) % m
            t_i, t_j = ring[i], ring[j]
            b_i, b_j = bottom_start + i, bottom_start + j
            faces.append((t_i, t_j, b_j))
            faces.append((t_i, b_j, b_i))

        b0 = bottom_start
        for i in range(1, m - 1):
            faces.append((b0, b0 + i + 1, b0 + i))

        mesh = trimesh.Trimesh(vertices=verts, faces=np.array(faces, dtype=np.int64), process=False)
        mesh.fix_normals()
        return mesh

    terrain_mesh = build_terrain_solid(xs - ORIGIN_EASTING, ys - ORIGIN_NORTHING, z_grid, TERRAIN_BASE_Z)
    terrain_mesh.export(terrain_obj_path)
    print(f"Terrain grid: {nx}x{ny} cells @ {TERRAIN_RESOLUTION_M:.0f}m, elevation "
          f"{np.nanmin(z_grid):.1f}-{np.nanmax(z_grid):.1f}m, base Z={TERRAIN_BASE_Z:.1f}m "
          f"(min elevation - {TERRAIN_BASE_OFFSET_M:.0f}m)")
    print(f"Saved -- {len(terrain_mesh.vertices):,} verts, {len(terrain_mesh.faces):,} faces, "
          f"watertight={terrain_mesh.is_watertight} -> {terrain_obj_path}  "
          f"({terrain_obj_path.stat().st_size/1e6:.2f} MB)")

print(f"--- 15. done in {time.time() - _t0:.2f}s ---\n")


### 15. Terrain solid mesh from the DEM (site-cropped) ###
Terrain grid: 204x204 cells @ 10m, elevation 709.3-786.0m, base Z=659.3m (min elevation - 50m)
Saved -- 42,428 verts, 84,852 faces, watertight=True -> ..\outputs\site_1_terrain.obj  (3.44 MB)
--- 15. done in 12.84s ---



---
## 16. Site contour lines, cropped and CAD-ready

<img src="https://github.com/ArchiColab/sitex/blob/main/images/Site3D_context.svg?raw=1" width="1000"/>

The ward-scale contour notebook produces contours for the whole ward. That works in
QGIS, but importing ward-wide contours into a 2 × 2 km CAD file is the same scale
problem Section 12 solved for land cover.

This section reuses the terrain grid already cropped and resampled in Section 15
(`xs`, `ys`, `z_grid`), so the DTM is not read again. The grid is smoothed and
contoured with `sitex.arch.terrain` (gaps with no data are handled), and the result is
exported as a DXF **shifted to the shared CAD origin**, like every other CAD export in
this notebook.

In [19]:
#@title <font color=#1B7192> Extract & export site contours </font>  { display-mode: "form" }
_t0 = time.time()
print("### 16. Site contour lines, cropped and CAD-ready ###", flush=True)

SITE_CONTOUR_INTERVAL = 2.0        #@param {type:"number"}
SITE_CONTOUR_SMOOTH_SIGMA = 1.0    #@param {type:"number"}
#@markdown <font color=#1B7192> Lighter than the ward-scale notebook's default (2.0) --
#@markdown the site DEM grid here is already a clean 10m resample, not the raw DTM. </font>

site_contour_dxf_path = OUTPUT_DIR / f"{SITE_SLUG}_contours.dxf"

if "z_grid" not in dir():
    print("[SKIPPED] No terrain grid (Section 15 skipped -- no DTM) -- no site contours.")
else:
    smoothed_z_grid = terrain.smooth_nan_aware(z_grid, SITE_CONTOUR_SMOOTH_SIGMA)
    site_contours = terrain.extract_contours(xs, ys, smoothed_z_grid, SITE_CONTOUR_INTERVAL, LOCAL_EPSG)
    print(f"{len(site_contours)} contour segments, "
          f"{site_contours['ELEV'].min():.0f}-{site_contours['ELEV'].max():.0f} m")

    terrain.export_contours_dxf(site_contours, site_contour_dxf_path, ORIGIN_EASTING, ORIGIN_NORTHING)
    print(f"Saved -> {site_contour_dxf_path}  (shifted by shared CAD origin "
          f"E={ORIGIN_EASTING:.0f}, N={ORIGIN_NORTHING:.0f})")

print(f"--- 16. done in {time.time() - _t0:.2f}s ---\n")


### 16. Site contour lines, cropped and CAD-ready ###
189 contour segments, 712-784 m
Saved -> ..\outputs\site_1_contours.dxf  (shifted by shared CAD origin E=175000, N=1547000)
--- 16. done in 4.72s ---



## 17. Drape land use + water onto the terrain, export context DXF

A land-use polygon can span real slopes across a 2 × 2 km site, so it does not get one
flat height. Instead, every vertex is given its own ground height from the DEM.

The DXF is organized in layers by class (`LU_<CLASS>` for land use, `WATER` for water),
so you can switch them on and off in Rhino, just like the building-function layers.

In [20]:
#@title <font color=#1B7192> Drape land use + water on the terrain, export context DXF </font>  { display-mode: "form" }
_t0 = time.time()
print("### 17. Drape land use + water onto the terrain, export context DXF ###", flush=True)

context_dxf_path = OUTPUT_DIR / f"{SITE_SLUG}_context.dxf"
doc_ctx = ezdxf.new(dxfversion="R2010")
msp_ctx = doc_ctx.modelspace()
transformer_to_utm_ctx = pyproj.Transformer.from_crs("EPSG:4326", f"EPSG:{LOCAL_EPSG}", always_xy=True)
context_layers = [(landuse_site, "class", "LU"), (water_site, None, "WATER")]

n_ctx_polys = 0
if not DTM_PATH.exists():
    print(f"[SKIPPED] {DTM_PATH} not found -- draping needs a DTM.")
else:
    with rasterio.open(DTM_PATH) as dtm:
        nodata = dtm.nodata
        for gdf, class_col, layer_prefix in context_layers:
            for _, row in gdf.iterrows():
                geom = row.geometry
                if geom is None or geom.is_empty:
                    continue
                layer = f"{layer_prefix}_{str(row[class_col]).upper()}" if class_col else layer_prefix
                polys = list(geom.geoms) if geom.geom_type == "MultiPolygon" else [geom]
                for poly in polys:
                    rings = [list(poly.exterior.coords)] + [list(r.coords) for r in poly.interiors]
                    for ring in rings:
                        lon = np.array([p[0] for p in ring])
                        lat = np.array([p[1] for p in ring])
                        z = np.array([next(dtm.sample([(lon[i], lat[i])]))[0] for i in range(len(lon))], dtype=float)
                        bad = (z == nodata) | np.isnan(z)
                        if bad.any():
                            z[bad] = np.nanmedian(z[~bad]) if (~bad).any() else 0.0
                        xy = [transformer_to_utm_ctx.transform(lo, la) for lo, la in zip(lon, lat)]
                        pts_3d = [(x - ORIGIN_EASTING, y - ORIGIN_NORTHING, float(zi)) for (x, y), zi in zip(xy, z)]
                        msp_ctx.add_polyline3d(pts_3d, dxfattribs={"layer": layer})
                    n_ctx_polys += 1

    doc_ctx.saveas(context_dxf_path)
    print(f"Saved {n_ctx_polys:,} land-use/water polygons draped on the terrain -> {context_dxf_path}")

print(f"--- 17. done in {time.time() - _t0:.2f}s ---\n")


### 17. Drape land use + water onto the terrain, export context DXF ###
Saved 6 land-use/water polygons draped on the terrain -> ..\outputs\site_1_context.dxf
--- 17. done in 0.06s ---



---
## 18. Inline 3D view (pydeck)

<img src="https://github.com/ArchiColab/sitex/blob/main/images/Site3D_view.svg?raw=1" width="1000"/>

In [21]:
#@title <font color=#1B7192> Click to Run </font>  { display-mode: "form" }

def prepare_3d_buildings(gdf, height_col="height_final", source_col="height_source",
                          cmap_name="plasma", vmax_percentile=95):
    gdf = gdf[gdf.geometry.notna() & gdf[height_col].notna() & (gdf[height_col] > 0)].copy()
    gdf_wgs = gdf if gdf.crs is None or gdf.crs.to_epsg() == 4326 else gdf.to_crs(epsg=4326)

    heights = gdf_wgs[height_col].to_numpy()
    vmax = max(float(np.percentile(heights, vmax_percentile)), 1.0)
    norm = mpl_colors.Normalize(vmin=0, vmax=vmax)
    cmap = mpl_cm.get_cmap(cmap_name)

    source = gdf_wgs[source_col].to_numpy()
    fill_colors = []
    for h, src in zip(heights, source):
        r, g, b, _ = cmap(norm(h))
        alpha = 90 if src == "imputed" else 220
        fill_colors.append([int(r * 255), int(g * 255), int(b * 255), alpha])

    coordinates = [[list(geom.exterior.coords)] for geom in gdf_wgs.geometry]
    centroid = gdf_wgs.geometry.union_all().centroid

    df = pd.DataFrame({
        "coordinates": coordinates,
        "height_final": np.round(heights, 1),
        "height_source": source,
        "bldg_function": gdf_wgs["bldg_function"].to_numpy(),
        "fill_color": fill_colors,
    })
    return df, centroid.y, centroid.x


def make_3d_deck(df, center_lat, center_lon, zoom=16, pitch=55, bearing=25):
    import pydeck as pdk
    layer = pdk.Layer(
        "PolygonLayer", df, get_polygon="coordinates", get_elevation="height_final",
        elevation_scale=1, extruded=True, get_fill_color="fill_color",
        pickable=True, auto_highlight=True,
    )
    view_state = pdk.ViewState(latitude=center_lat, longitude=center_lon, zoom=zoom, pitch=pitch, bearing=bearing)
    tooltip = {"text": "Height: {height_final} m\nSource: {height_source}\nFunction: {bldg_function}"}
    return pdk.Deck(layers=[layer], initial_view_state=view_state, map_provider=None, tooltip=tooltip)


viz_df, viz_lat, viz_lon = prepare_3d_buildings(buildings)
n_real = (viz_df["height_source"] != "imputed").sum()
n_imputed = (viz_df["height_source"] == "imputed").sum()
print(f"{len(viz_df):,} buildings in the 3D view -- {n_real:,} real, {n_imputed:,} imputed")

deck = make_3d_deck(viz_df, viz_lat, viz_lon)
deck


4,813 buildings in the 3D view -- 4,687 real, 126 imputed


{
  "initialViewState": {
    "bearing": 25,
    "latitude": 13.987025177397888,
    "longitude": 108.0193790469793,
    "pitch": 55,
    "zoom": 16
  },
  "layers": [
    {
      "@@type": "PolygonLayer",
      "autoHighlight": true,
      "data": [
        {
          "bldg_function": "residential",
          "coordinates": [
            [
              [
                108.0159024,
                13.980186299999996
              ],
              [
                108.01589887602945,
                13.980150590431574
              ],
              [
                108.01585547133783,
                13.980150589556695
              ],
              [
                108.0158594,
                13.9801904
              ],
              [
                108.0159024,
                13.980186299999996
              ]
            ]
          ],
          "fill_color": [
            183,
            48,
            138,
            220
          ],
          "height_final": 2.9,
          "height_source": "gba"
        },
        {
          "bldg_function": "residential",
          "coordinates": [
            [
              [
                108.0159073,
                13.980236299999998
              ],
              [
                108.0159024,
                13.980186299999996
              ],
              [
                108.0158594,
                13.9801904
              ],
              [
                108.0158644,
                13.980240399999998
              ],
              [
                108.0159073,
                13.980236299999998
              ]
            ]
          ],
          "fill_color": [
            209,
            78,
            114,
            220
          ],
          "height_final": 3.6,
          "height_source": "gba"
        },
        {
          "bldg_function": "residential",
          "coordinates": [
            [
              [
                108.015693,
                13.980301699999998
              ],
              [
                108.01586830000001,
                13.980284299999996
              ],
              [
                108.0158584,
                13.9801894
              ],
              [
                108.0156831,
                13.980206900000002
              ],
              [
                108.015693,
                13.980301699999998
              ]
            ]
          ],
          "fill_color": [
            246,
            145,
            66,
            220
          ],
          "height_final": 5.0,
          "height_source": "open_buildings"
        },
        {
          "bldg_function": "residential",
          "coordinates": [
            [
              [
                108.0170203,
                13.980328199999999
              ],
              [
                108.01708190000001,
                13.9803268
              ],
              [
                108.01707950000001,
                13.980228899999998
              ],
              [
                108.0170178,
                13.9802304
              ],
              [
                108.0170203,
                13.980328199999999
              ]
            ]
          ],
          "fill_color": [
            212,
            82,
            110,
            220
          ],
          "height_final": 3.7,
          "height_source": "gba"
        },
        {
          "bldg_function": "residential",
          "coordinates": [
            [
              [
                108.0169705,
                13.980227
              ],
              [
                108.0168928,
                13.9802245
              ],
              [
                108.0168895,
                13.980321699999998
              ],
              [
                108.0169323,
                13.980323100000001
              ],
              [
                108.01693000000002,
                13.9803907
              ],
              [
                108.0169648,
    

---
## 19. Summary

In [22]:
#@title <font color=#1B7192> Click to Run </font>  { display-mode: "form" }

SEP = "=" * 55
print(SEP)
print("  Site 3D Model Summary")
print(SEP)
print(f"  Site               : {SITE_SLUG}  (from district {DISTRICT_SLUG})")
print(f"  Buildings          : {len(buildings):,}")
print(f"  Shared CAD origin  : E={ORIGIN_EASTING:.0f}, N={ORIGIN_NORTHING:.0f}")
print(f"  Flat DXF           : {flat_dxf_path}")
print(f"  DEM-draped DXF     : {dem_dxf_path}")
print(f"  site.obj           : {site_obj_path}")
print(f"  Land cover DXF     : {lc_dxf_path}")
print(f"  Land cover .obj    : {landcover_obj_path}  ({LC_THICKNESS_M:.1f}m slabs, per-class colour)")
print(f"  Terrain solid .obj : {terrain_obj_path}")
print(f"  Site contours DXF  : {site_contour_dxf_path}  (cropped, origin-shifted)")
print(f"  Context DXF        : {context_dxf_path}  (land use + water, draped)")
print("\nAll outputs import at the same origin as 01-ARCH-DEM_Contour.ipynb's contour "
      "DXF -- drape the land-cover DXF/obj (or the vector context DXF from Section 17) "
      "onto a Rhino terrain surface built from the site contours (Section 16) or "
      "straight onto the terrain .obj from Section 15, then bring in the buildings "
      "on top.")


  Site 3D Model Summary
  Site               : site_1  (from district pleiku)
  Buildings          : 4,813
  Shared CAD origin  : E=175000, N=1547000
  Flat DXF           : ..\outputs\site_1_buildings_flat.dxf
  DEM-draped DXF     : ..\outputs\site_1_buildings_dem.dxf
  site.obj           : ..\outputs\site_1_site.obj
  Land cover DXF     : ..\outputs\site_1_landcover.dxf
  Land cover .obj    : ..\outputs\site_1_landcover.obj  (0.3m slabs, per-class colour)
  Terrain solid .obj : ..\outputs\site_1_terrain.obj
  Site contours DXF  : ..\outputs\site_1_contours.dxf  (cropped, origin-shifted)
  Context DXF        : ..\outputs\site_1_context.dxf  (land use + water, draped)

All outputs import at the same origin as 01-ARCH-DEM_Contour.ipynb's contour DXF -- drape the land-cover DXF/obj (or the vector context DXF from Section 17) onto a Rhino terrain surface built from the site contours (Section 16) or straight onto the terrain .obj from Section 15, then bring in the buildings on top.
